In [1]:
from ImpararePackage import dataRequest

# Data load

In [2]:
GABARITO = "caso infeccao"
path = "/workspaces/imparare-surface-materdei-neo/ScriptsLibrary/pipeline/T6/after training"
query = f"""
    SELECT 
        pa."{GABARITO}",
        dtf.*
    FROM imparare2_dataset_label_full  dtf
    inner join new_avaliacao_padrao_ouro pa
        on dtf.prontuario = pa.registro 
            and dtf."dia_parsed" = pa.dt_infeccao
"""
df = dataRequest.get_data(query, chunck= None)

In [3]:
df

,caso infeccao,prontuario,dia_parsed,idade_anos,idade_dias,los_dias,cirurgia_tempo_total,cirurgia_procedimentos_total,cirurgia_em_30_dias,cirurgia_em_90_dias,...,hiperemia_passado,hiperemia_passado_sent_pos_count,estase_gastr_passado,estase_gastr_passado_sent_pos_count,desc_respirat_passado,desc_respirat_passado_sent_pos_count,distensao_abdominal_passado,distensao_abdominal_passado_sent_pos_count,hipocorado_passado,hipocorado_passado_sent_pos_count
0,False,2119385,2025-02-19,0,27,27,0,0,False,False,...,NaN,0,NaN,0,1.0,8,1.0,3,1.0,4
1,False,1813539,2023-06-17,0,0,0,0,0,False,False,...,NaN,0,NaN,0,NaN,0,NaN,0,NaN,0
2,True,1947303,2024-05-20,0,88,88,0,0,True,True,...,1.0,1,NaN,0,NaN,0,1.0,9,1.0,11
3,False,1841940,2023-08-12,0,2,2,0,0,False,False,...,NaN,0,NaN,0,0.0,0,1.0,2,NaN,0
4,False,199319,2023-09-15,0,0,0,0,0,False,False,...,NaN,0,NaN,0,NaN,0,NaN,0,NaN,0
...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...
36236,False,2078566,2024-11-01,0,1,1,0,0,False,False,...,NaN,0,NaN,0,NaN,0,NaN,0,NaN,0
36237,False,1947853,2024-02-22,0,0,0,0,0,False,False,...,NaN,0,NaN,0,NaN,0,NaN,0,NaN,0
36238,False,1886900,2023-10-31,0,0,0,0,0,False,False,...,NaN,0,NaN,0,NaN,0,NaN,0,NaN,0
36239,False,1886900,2023-10-31,0,0,0,0,0,False,False,...,NaN,0,NaN,0,NaN,0,NaN,0,NaN,0


# Data prepare

In [ ]:
import pandas as pd
from sklearn.impute import SimpleImputer

id_cols   = ["prontuario", "dia_parsed"]   # o "par" que identifica o dado (chave composta)

# metadados que NÃO entram nas features
y   = df[GABARITO].values
ids = df[id_cols].reset_index(drop=True)

# features = tudo menos label e ids
feature_cols = [c for c in df.columns if c not in id_cols + [GABARITO]]

# Coage TODAS as features para numérico de uma vez:
#   - bool  -> 0/1
#   - strings/valores inválidos -> NaN
# Usa pd.to_numeric(errors="coerce") em vez de .astype("Int64"): o Int64 é o
# inteiro *nullable* do pandas, cujo missing é pd.NA (NAType). Ao chamar .values
# o array vira object com pd.NA e o SimpleImputer quebra em float(pd.NA).
# to_numeric gera float64 com np.nan, que o sklearn entende.
X_df = df[feature_cols].apply(pd.to_numeric, errors="coerce")

# sanity check: agora as features TÊM que ser todas numéricas pra escalar/PCA
nao_numericas = X_df.select_dtypes(exclude="number").columns.tolist()
assert not nao_numericas, f"Colunas não-numéricas nas features: {nao_numericas}"

X = X_df.astype("float64").values
X = SimpleImputer(strategy="median").fit_transform(X)

In [ ]:
# quantos NaN por coluna de feature (só as que têm > 0)
na_por_coluna = df[feature_cols].isna().sum()
print(na_por_coluna[na_por_coluna > 0].sort_values(ascending=False))

# quantas LINHAS têm pelo menos um NaN nas features
linhas_com_na = df[feature_cols].isna().any(axis=1).sum()
print(f"\nLinhas afetadas: {linhas_com_na} de {len(df)} "
      f"({100*linhas_com_na/len(df):.1f}%)")

pneumatose_hoje                  36170
pneumatose_futuro                36143
pneumatose_passado               36129
perfuracao_futuro                36051
perfuracao_hoje                  35949
                                 ...  
FR_ALTERADA                      10494
FC_ALTA                          10494
FC_ALTERADA                      10494
FC_BAIXA                         10494
SINAIS_VITAIS_registros_total    10494
Length: 88, dtype: int64

Linhas afetadas: 36243 de 36243 (100.0%)


# Ploting with T-SNE

In [ ]:
# pip install scikit-learn umap-learn plotly pandas numpy
import numpy as np
import pandas as pd
import plotly.express as px

from sklearn.preprocessing import StandardScaler
from sklearn.decomposition import PCA
from sklearn.manifold import TSNE
import umap  # pacote: umap-learn, mas o import é "umap"

# ------------------------------------------------------------------
# 2) Pré-processamento comum aos dois
# ------------------------------------------------------------------
X_scaled = StandardScaler().fit_transform(X)

n_pca = min(50, X_scaled.shape[1])
X_pca = PCA(n_components=n_pca, random_state=42).fit_transform(X_scaled)

# ------------------------------------------------------------------
# 3) As reduções
# ------------------------------------------------------------------
def run_tsne(X, n_components):
    return TSNE(
        n_components=n_components,
        perplexity=30,        # KNOB principal: ~5 a 50. Datasets menores -> menor.
        learning_rate="auto",
        init="pca",
        random_state=42,
    ).fit_transform(X)

def run_umap(X, n_components):
    return umap.UMAP(
        n_components=n_components,
        n_neighbors=15,       # KNOB: análogo à perplexity.
        min_dist=0.1,
        random_state=42,
    ).fit_transform(X)

emb = {
    "t-SNE 2D": run_tsne(X_pca, 2),
    "UMAP 2D":  run_umap(X_pca, 2),
    "t-SNE 3D": run_tsne(X_pca, 3),
    "UMAP 3D":  run_umap(X_pca, 3),
}

# ------------------------------------------------------------------
# 4) Helper: monta o DataFrame de plot (coords + label + ids)
# ------------------------------------------------------------------
def make_plot_df(e, dims):
    cols = ["x", "y", "z"][:dims]
    pdf = pd.DataFrame(e, columns=cols)
    pdf["label"] = y.astype(str)        # string -> legenda categórica/cor por classe
    return pd.concat([pdf, ids], axis=1)

# ------------------------------------------------------------------
# 5) Plots 2D (interativos, com hover dos ids)
# ------------------------------------------------------------------
for name in ["t-SNE 2D", "UMAP 2D"]:
    pdf = make_plot_df(emb[name], dims=2)
    fig = px.scatter(
        pdf, x="x", y="y",
        color="label",
        hover_data=id_cols,
        opacity=0.7, title=name,
    )
    fig.update_traces(marker_size=6)
    fig.update_xaxes(visible=False); fig.update_yaxes(visible=False)
    fig.show()

# ------------------------------------------------------------------
# 6) Plots 3D (interativos — rotaciona e passa o mouse pra ver os ids)
# ------------------------------------------------------------------
for name in ["t-SNE 3D", "UMAP 3D"]:
    pdf = make_plot_df(emb[name], dims=3)
    fig3d = px.scatter_3d(
        pdf, x="x", y="y", z="z",
        color="label",
        hover_data=id_cols,
        opacity=0.7, title=name,
    )
    fig3d.update_traces(marker_size=3)
    fig3d.show()

/home/linux-5900xt/Desktop/imparare-surface-materdei-neo/.venv/lib/python3.13/site-packages/tqdm/auto.py:21: TqdmWarning: IProgress not found. Please update jupyter and ipywidgets. See https://ipywidgets.readthedocs.io/en/stable/user_install.html
  from .autonotebook import tqdm as notebook_tqdm
/home/linux-5900xt/Desktop/imparare-surface-materdei-neo/.venv/lib/python3.13/site-packages/umap/umap_.py:1952: UserWarning: n_jobs value 1 overridden to 1 by setting random_state. Use no seed for parallelism.
  warn(
/home/linux-5900xt/Desktop/imparare-surface-materdei-neo/.venv/lib/python3.13/site-packages/umap/umap_.py:1952: UserWarning: n_jobs value 1 overridden to 1 by setting random_state. Use no seed for parallelism.
  warn(
